In [1]:
import utils
import numpy as np
import pandas as pd
import os
import re

import matplotlib.pyplot as plt
import seaborn as sns # Loads in the theme
sns.set_theme()

pd.set_option('future.no_silent_downcasting', True)
pd.set_option('display.max_rows', None)
pd.set_option('display.width', 1000)

In [2]:
# Make output folders
output_dir = os.path.join('/Volumes/project/3025011.02/pre-processed/behaviour')
if not os.path.exists(output_dir):
    os.makedirs(output_dir)

In [3]:
# Preparation
pilot_analysis = False
unique_subject_ids = [5, 10, 11, 14]#[802,803,804,805,806,807,808,809,810,811,813,814,815]
unique_sessions = [2, 3, 4]
plot_range = [0, 6]

if pilot_analysis:
    raw_output_path = '/Volumes/project/3025011.02/pilot_data/phd_1_task/experiment_output/behavioural_files_pilot_2'
else:
    raw_output_path = '/Volumes/project/3025011.02/raw/'
recent_results = utils.analysis_functions.list_files_with_date_and_subject_id(raw_output_path, unique_subject_ids, unique_sessions)

In [4]:
if not recent_results:
    raise Exception('No files found')
print(recent_results)

['/Volumes/project/3025011.02/raw/sub-005/ses-mri02/beh/behavioural_output_sub-005_session-02_skyra_2025-03-14_11-00-23.csv', '/Volumes/project/3025011.02/raw/sub-005/ses-mri03/beh/behavioural_output_sub-005_session-03_skyra_2025-03-21_15-48-02.csv', '/Volumes/project/3025011.02/raw/sub-005/ses-mri04/beh/behavioural_output_sub-005_session-04_skyra_2025-03-28_15-50-17.csv', '/Volumes/project/3025011.02/raw/sub-010/ses-mri02/beh/behavioural_output_sub-010_session-02_skyra_2025-03-13_11-21-05.csv', '/Volumes/project/3025011.02/raw/sub-010/ses-mri03/beh/behavioural_output_sub-010_session-03_skyra_2025-03-19_11-41-24.csv', '/Volumes/project/3025011.02/raw/sub-010/ses-mri04/beh/behavioural_output_sub-010_session-04_skyra_2025-03-25_15-18-37.csv', '/Volumes/project/3025011.02/raw/sub-011/ses-mri02/beh/behavioural_output_sub-011_session-02_skyra_2025-04-04_16-07-03.csv', '/Volumes/project/3025011.02/raw/sub-011/ses-mri03/beh/behavioural_output_sub-011_session-03_skyra_2025-04-11_11-31-46.csv',

In [5]:
### Remove invalid files
# Remove files that contain invalid data
raw_output_path = '/Volumes/project/3025011.02/raw/'
invalid_data = pd.read_csv(f'{raw_output_path}../incomplete_data.csv', delimiter=';')
combinations = {
    f"sub-{row['subject-id']:03}_session-{row['session-number']:02}"
    for _, row in invalid_data[invalid_data['datatype'] == 'beh'].iterrows()
}
print(f'These participants will be excluded: {combinations}')

patterns = [re.compile(re.escape(combo)) for combo in combinations]
# Filter the list: remove any string that contains one of the combinations
recent_results = [
    item for item in recent_results
    if not any(pattern.search(item) for pattern in patterns)
]
print(recent_results)

These participants will be excluded: {'sub-003_session-03'}
['/Volumes/project/3025011.02/raw/sub-005/ses-mri02/beh/behavioural_output_sub-005_session-02_skyra_2025-03-14_11-00-23.csv', '/Volumes/project/3025011.02/raw/sub-005/ses-mri03/beh/behavioural_output_sub-005_session-03_skyra_2025-03-21_15-48-02.csv', '/Volumes/project/3025011.02/raw/sub-005/ses-mri04/beh/behavioural_output_sub-005_session-04_skyra_2025-03-28_15-50-17.csv', '/Volumes/project/3025011.02/raw/sub-010/ses-mri02/beh/behavioural_output_sub-010_session-02_skyra_2025-03-13_11-21-05.csv', '/Volumes/project/3025011.02/raw/sub-010/ses-mri03/beh/behavioural_output_sub-010_session-03_skyra_2025-03-19_11-41-24.csv', '/Volumes/project/3025011.02/raw/sub-010/ses-mri04/beh/behavioural_output_sub-010_session-04_skyra_2025-03-25_15-18-37.csv', '/Volumes/project/3025011.02/raw/sub-011/ses-mri02/beh/behavioural_output_sub-011_session-02_skyra_2025-04-04_16-07-03.csv', '/Volumes/project/3025011.02/raw/sub-011/ses-mri03/beh/behaviour

In [6]:
combined_results_dataframe = utils.analysis_functions.combine_result_files(recent_results)
if pilot_analysis:
    combined_results_dataframe.rename(columns={'iti': 'trial_duration'}, inplace=True)
    combined_results_dataframe['stimuli_type'] = combined_results_dataframe['stimuli_type'].replace(3, 2)
print(combined_results_dataframe)

      trial  emotional_cue_time response objectively_correct subjectively_correct  response_time   RT_s  feedback_time  stimuli_type  trial_duration  probability_condition  face_type stimuli_name  reward_amount subject_id     session
0         0        1.741947e+09     down                Even                False   1.741947e+09  0.692   1.741947e+09             1        3.704648                     50          3     Angry_b3           -0.1    sub-005  session-02
1         1        1.741947e+09       up                Even                 True   1.741947e+09  0.940   1.741947e+09             1        4.295352                     50          2     Angry_b2            0.0    sub-005  session-02
2         2        1.741947e+09       up                Even                 True   1.741947e+09  0.793   1.741947e+09             1        3.302849                     50          1     Angry_b1            0.1    sub-005  session-02
3         3        1.741947e+09     down                Even    

# Flip results if joystick orientation was incorrect
Specifically, switch the response and probability

In [7]:
# List of subject_session combinations to update
match_list = ['sub-004_session-04']

# Create a new column that combines subject_id and session in the same format as the list.
combined_results_dataframe['sub_session'] = combined_results_dataframe['subject_id'] + '_' + combined_results_dataframe['session']

# Create a mask for rows that match any of the combinations in match_list.
mask = combined_results_dataframe['sub_session'].isin(match_list)

# For 'probability_condition', swap 80 with 20 and vice versa.
combined_results_dataframe.loc[mask, 'probability_condition'] = (
    combined_results_dataframe.loc[mask, 'probability_condition']
    .replace({80: 20, 20: 80})
)

# For 'response', swap 'up' with 'down' and vice versa.
combined_results_dataframe.loc[mask, 'response'] = (
    combined_results_dataframe.loc[mask, 'response']
    .replace({'up': 'down', 'down': 'up'})
)

# Optionally, drop the helper column
combined_results_dataframe.drop(columns='sub_session', inplace=True)

print(combined_results_dataframe)

      trial  emotional_cue_time response objectively_correct subjectively_correct  response_time   RT_s  feedback_time  stimuli_type  trial_duration  probability_condition  face_type stimuli_name  reward_amount subject_id     session
0         0        1.741947e+09     down                Even                False   1.741947e+09  0.692   1.741947e+09             1        3.704648                     50          3     Angry_b3           -0.1    sub-005  session-02
1         1        1.741947e+09       up                Even                 True   1.741947e+09  0.940   1.741947e+09             1        4.295352                     50          2     Angry_b2            0.0    sub-005  session-02
2         2        1.741947e+09       up                Even                 True   1.741947e+09  0.793   1.741947e+09             1        3.302849                     50          1     Angry_b1            0.1    sub-005  session-02
3         3        1.741947e+09     down                Even    

# Remove non-responses

In [8]:
mask = ~(combined_results_dataframe['response'].isna() | combined_results_dataframe['objectively_correct'].str.contains('Late', na=False))
combined_results_dataframe = combined_results_dataframe[mask]

# Check congruency, valence and volatility

In [9]:
# Check a block's congruency
combined_results_dataframe['congruency'] = combined_results_dataframe.apply(utils.analysis_functions.check_congruency, args=(True,), axis=1)

# Check a block's valence
combined_results_dataframe['valence'] = combined_results_dataframe.apply(utils.analysis_functions.check_valence, args=(True,), axis=1)

# Check the stimulation condition
combined_results_dataframe['stimulation_condition'] = combined_results_dataframe.apply(utils.analysis_functions.check_stimulation_condition, args=(True,), axis=1)

# Add WSLS columns
combined_results_dataframe = utils.learning_models.add_WSLS_column(combined_results_dataframe)

# Check a block's volatility
combined_results_dataframe = combined_results_dataframe[combined_results_dataframe['probability_condition'] != 50]
combined_results_dataframe = combined_results_dataframe.groupby('stimuli_type', group_keys=False).apply(lambda x: utils.analysis_functions.check_volatility(x, True))
combined_results_dataframe = combined_results_dataframe.sort_values(by=['stimuli_type','trial'], ascending=[True, True])
print(combined_results_dataframe[['volatility','probability_condition']])
combined_results_dataframe = combined_results_dataframe.sort_values(by=['subject_id', 'session', 'stimuli_type', 'trial'], ascending=[True, True, True, True])
combined_results_dataframe.reset_index(drop=True, inplace=True)
print(combined_results_dataframe[['subject_id', 'session', 'congruency', 'valence', 'volatility']])
print(combined_results_dataframe.shape[0])

print(combined_results_dataframe['valence'].unique())
print(combined_results_dataframe['congruency'].unique())
print(combined_results_dataframe['volatility'].unique())

     subject_id     session subjectively_correct_one_back subjectively_correct  same_response_as_one_back  WS_subjective  LS_subjective
0       sub-005  session-02                           NaN                False                          0              0              0
1       sub-005  session-02                         False                 True                          0              0              1
2       sub-005  session-02                          True                 True                          1              1              0
3       sub-005  session-02                          True                False                          0             -1              0
4       sub-005  session-02                         False                False                          0              0              1
5       sub-005  session-02                         False                False                          1              0             -1
6       sub-005  session-02                     

/var/folders/bh/ld02p1_550d75y0x32dmpb540000gp/T/ipykernel_11282/2206143444.py:15: DeprecationWarning: DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.
  combined_results_dataframe = combined_results_dataframe.groupby('stimuli_type', group_keys=False).apply(lambda x: utils.analysis_functions.check_volatility(x, True))


In [10]:
print(combined_results_dataframe[['subject_id','session','stimuli_type','response','response_one_back','response_two_back','choicestickiness']])

     subject_id     session  stimuli_type response response_one_back response_two_back  choicestickiness
0       sub-005  session-02             1       up              down                up                 0
1       sub-005  session-02             1       up                up              down                 0
2       sub-005  session-02             1       up                up                up                 1
3       sub-005  session-02             1     down                up                up                 1
4       sub-005  session-02             1     down              down                up                 0
5       sub-005  session-02             1     down              down              down                 1
6       sub-005  session-02             1       up              down              down                 1
7       sub-005  session-02             1     down                up              down                 0
8       sub-005  session-02             1     down     

### Add a response bias column

In [11]:
# Takes the average chance of a pull response and puts that value in every row
combined_results_dataframe['response_bias'] = (
    combined_results_dataframe['response'].eq('down')
      .groupby([combined_results_dataframe['subject_id'], combined_results_dataframe['session']])
      .transform('mean')
).astype(float)

print(combined_results_dataframe[['subject_id','session','response_bias']])

     subject_id     session  response_bias
0       sub-005  session-02       0.513720
1       sub-005  session-02       0.513720
2       sub-005  session-02       0.513720
3       sub-005  session-02       0.513720
4       sub-005  session-02       0.513720
5       sub-005  session-02       0.513720
6       sub-005  session-02       0.513720
7       sub-005  session-02       0.513720
8       sub-005  session-02       0.513720
9       sub-005  session-02       0.513720
10      sub-005  session-02       0.513720
11      sub-005  session-02       0.513720
12      sub-005  session-02       0.513720
13      sub-005  session-02       0.513720
14      sub-005  session-02       0.513720
15      sub-005  session-02       0.513720
16      sub-005  session-02       0.513720
17      sub-005  session-02       0.513720
18      sub-005  session-02       0.513720
19      sub-005  session-02       0.513720
20      sub-005  session-02       0.513720
21      sub-005  session-02       0.513720
22      sub

### Now add a column with 'time_since_switch'

In [16]:
combined_results_dataframe = combined_results_dataframe.sort_values(by=['subject_id', 'session', 'stimuli_type', 'trial'], ascending=[True, True, True, True])
combined_results_dataframe['time_since_switch'] = (
    combined_results_dataframe.groupby((combined_results_dataframe['probability_condition'] != combined_results_dataframe['probability_condition'].shift()).cumsum())
      .cumcount()
)
print(combined_results_dataframe[['time_since_switch','probability_condition']])

      time_since_switch  probability_condition
2                     0                     20
3                     1                     20
4                     2                     20
5                     3                     20
6                     4                     20
7                     5                     20
8                     6                     20
9                     7                     20
10                    8                     20
11                    9                     20
12                   10                     20
13                   11                     20
14                   12                     20
15                   13                     20
16                   14                     20
17                   15                     20
18                   16                     20
19                   17                     20
20                   18                     20
21                   19                     20
22           

# Now add dummy variables for the stimulation condition

In [13]:
combined_results_dataframe['session_2'] = (combined_results_dataframe['session'] == 'session-02').astype(int)
combined_results_dataframe['session_3'] = (combined_results_dataframe['session'] == 'session-03').astype(int)
combined_results_dataframe['session_4'] = (combined_results_dataframe['session'] == 'session-04').astype(int)
print(combined_results_dataframe[['session','session_2', 'session_3','session_4']])

         session  session_2  session_3  session_4
0     session-02          1          0          0
1     session-02          1          0          0
2     session-02          1          0          0
3     session-02          1          0          0
4     session-02          1          0          0
5     session-02          1          0          0
6     session-02          1          0          0
7     session-02          1          0          0
8     session-02          1          0          0
9     session-02          1          0          0
10    session-02          1          0          0
11    session-02          1          0          0
12    session-02          1          0          0
13    session-02          1          0          0
14    session-02          1          0          0
15    session-02          1          0          0
16    session-02          1          0          0
17    session-02          1          0          0
18    session-02          1          0          0


# Recode existing variables

In [14]:
combined_results_dataframe = combined_results_dataframe.dropna(subset=['response'])
# Add drop WSLS here
WSLS_columns = ['WS_subjective', 'LS_subjective', 'WS_objective', 'LS_objective']
combined_results_dataframe_grouped = combined_results_dataframe.groupby(
    ['subject_id', 'session', 'stimuli_type'],
    sort=False
).cumcount()

# cumcount()==0 is the very first row in each group,
# cumcount()==1 is the second; we want both.
combined_results_dataframe.loc[combined_results_dataframe_grouped.isin([0, 1]), WSLS_columns] = np.nan

print(combined_results_dataframe[['stimuli_type','WS_subjective', 'LS_subjective', 'WS_objective', 'LS_objective']])
combined_results_dataframe = combined_results_dataframe.dropna(subset=WSLS_columns)
'''
combined_results_dataframe = utils.analysis_functions.replace_strings_with_integers(combined_results_dataframe,
                                                                                    {'up': 2, 'down': 1},
                                                                                    'response',
                                                                                    'response_int')

combined_results_dataframe = utils.analysis_functions.replace_strings_with_integers(combined_results_dataframe,
                                                                                    {'True': 1, 'False': 0},
                                                                                    'subjectively_correct',
                                                                                    'subjectively_correct_int')

combined_results_dataframe = utils.analysis_functions.replace_strings_with_integers(combined_results_dataframe,
                                                                                    {'True': 1, 'False': 0},
                                                                                    'subjectively_correct_one_back',
                                                                                    'subjectively_correct_one_back_int')

combined_results_dataframe = utils.analysis_functions.replace_strings_with_integers(combined_results_dataframe,
                                                                                    {'True': 1, 'False': 0},
                                                                                    'objectively_correct',
                                                                                    'objectively_correct_int')

#combined_results_dataframe['subject_id'] = combined_results_dataframe['subject_id'].str.replace(r'\D', '', regex=True)
#combined_results_dataframe['session'] = combined_results_dataframe['session'].str.replace(r'\D', '', regex=True)
'''

      stimuli_type  WS_subjective  LS_subjective  WS_objective  LS_objective
0                1            NaN            NaN           NaN           NaN
1                1            NaN            NaN           NaN           NaN
2                1            0.0           -1.0           0.0          -1.0
3                1            0.0            1.0           0.0           1.0
4                1            1.0            0.0           1.0           0.0
5                1            1.0            0.0           1.0           0.0
6                1           -1.0            0.0          -1.0           0.0
7                1            0.0            1.0           0.0           1.0
8                1            0.0           -1.0           1.0           0.0
9                1            1.0            0.0           1.0           0.0
10               1            1.0            0.0           1.0           0.0
11               1            1.0            0.0           1.0           0.0

"\ncombined_results_dataframe = utils.analysis_functions.replace_strings_with_integers(combined_results_dataframe,\n                                                                                    {'up': 2, 'down': 1},\n                                                                                    'response',\n                                                                                    'response_int')\n\ncombined_results_dataframe = utils.analysis_functions.replace_strings_with_integers(combined_results_dataframe,\n                                                                                    {'True': 1, 'False': 0},\n                                                                                    'subjectively_correct',\n                                                                                    'subjectively_correct_int')\n\ncombined_results_dataframe = utils.analysis_functions.replace_strings_with_integers(combined_results_dataframe,\n                 

# Now export the data

In [15]:
combined_results_dataframe = combined_results_dataframe.sort_values(by=['subject_id', 'session', 'trial'], ascending=[True, True, True])
combined_results_dataframe.to_csv(f'{output_dir}/combined_dataframe_for_r.csv', sep=';', index_label='index')